# Fluid TIQ thresholds and local refinement

This notebook studies how fluid-based TIQ thresholds can be used to initialize a simulation policy, and whether a small local search improves performance.

The workflow is:

1. choose a patience distribution with a non-monotone hazard  
2. solve for fluid thresholds $$w_\ell$$ and $$w_h$$  
3. construct the corresponding TIQ policy  
4. compare FCFS, LCFS, and fluid-initialized TIQ  
5. refine the thresholds with a local search in simulation


Earlier notebooks compared fixed policies under different hazard shapes.

This notebook moves one step closer to the Bassamboo framework by connecting:

- a **fluid approximation**
- an **implementable TIQ policy**
- a **simulation-based performance comparison**

The main question is whether fluid-derived thresholds provide a useful starting point for queue control in the stochastic system.

## Setup

We consider an overloaded single-class system with

$$
\lambda = 20, \quad N = 10, \quad \mu = 1.
$$

The patience distribution is chosen to have a non-monotone hazard, since this is the regime where a two-threshold TIQ rule is theoretically relevant.

In [1]:
import pandas as pd

from gi_gi_n_gi_multiclass.core.engine import run_sim
from gi_gi_n_gi_multiclass.core.types import SimConfig
from gi_gi_n_gi_multiclass.dists.common import Exponential, Weibull
from gi_gi_n_gi_multiclass.policies.fcfs import FCFS
from gi_gi_n_gi_multiclass.policies.lcfs import LCFS
from gi_gi_n_gi_multiclass.metrics.basic import summary_table

from gi_gi_n_gi_multiclass.policies.tiq import TIQ
from gi_gi_n_gi_multiclass.metrics.steady_state import time_average_L


## Step 1: Solve the fluid threshold problem

We first solve the fluid approximation to obtain a candidate pair

$$
w_\ell, \quad w_h.
$$

These thresholds define the waiting-time regions used by the TIQ policy.

The point of this step is not to claim that the fluid thresholds are exactly optimal in simulation, but rather to use them as a principled initialization.

In [2]:

from gi_gi_n_gi_multiclass.fluid.threshold_solver import solve_two_threshold_fluid
from gi_gi_n_gi_multiclass.dists.common import LogNormal, Weibull, Exponential

lam = 20.0
N = 10
mean_service = 1.0   # m = E[service time]

patience = LogNormal(meanlog=0.0, sdlog=1.0)  # example where hazard can be non-monotone

sol = solve_two_threshold_fluid(
    objective="queue_length",
    patience=patience,
    lam=20.0,
    n_servers=10,
    mean_service=1.0,
    w_max=30.0,
    n_grid=5000,
    n_levels=250,
)

sol

FluidSolution(w_l=0.39455210845736843, w_h=1.0088169978711923, p=0.010699127940995484, level=0.7964590376697974, obj_value=0.7617263245279696)

## Step 2: Construct the TIQ policy

Using the fluid solution, we build a TIQ policy with thresholds

$$
w_\ell = \text{sol.w\_l}, \qquad w_h = \text{sol.w\_h}.
$$

This gives a direct simulation analogue of the fluid recommendation.

In [ ]:
from gi_gi_n_gi_multiclass.policies.tiq import TIQ

tiq_policy = TIQ(w_l=sol.w_l, w_h=sol.w_h)
tiq_policy

TIQ(w_l=0.546129367573237, w_h=0.7016725001250105, name='TIQ')

## Step 3: Compare baseline policies

We compare three policies:

- FCFS  
- LCFS  
- TIQ initialized from the fluid thresholds  

The goal is to see whether the fluid-based TIQ already improves on the standard queue disciplines.

In [ ]:
warmup_time = 500.0
run_time = 2000.0
seed = 123

interarrival = Exponential(rate=lam)     # lambda
service = Exponential(rate=1.0)          # mean service = 1

# Match the patience distribution used in the solver (Weibull k=0.7, scale=2.0)
patience = LogNormal(meanlog=0.0, sdlog=1.0) 

policies = {
    "FCFS": FCFS(),
    "LCFS": LCFS(),
    "TIQ_fluid": tiq_policy,
}

rows = []
for pol_name, pol in policies.items():
    cfg = SimConfig(
        n_servers=N,
        interarrival=interarrival,
        service=service,
        patience=patience,
        policy=pol,
        seed=seed,
        warmup_time=warmup_time,
        run_time=run_time,
        collect_event_log=False,
    )
    res = run_sim(cfg)
    tbl = summary_table(res)
    tbl["policy_name"] = pol_name
    rows.append(tbl)

out = pd.concat(rows, ignore_index=True)
out

,policy,n_servers,arrivals,served,abandoned,lambda_hat,served_rate,abandon_rate,W_mean,service_mean,patience_mean,L_timeavg,Lq_timeavg,end_time,policy_name
0,FCFS,10,40027,19888,20120,20.0135,9.9440,10.0600,1.963555,0.999417,1.642566,25.247650,15.248472,2500.0,FCFS
1,LCFS,10,40027,19981,20029,20.0135,9.9905,10.0145,1.106395,0.999417,1.642566,26.940251,16.940421,2500.0,LCFS
2,TIQ,10,40027,19968,20040,20.0135,9.9840,10.0200,1.952416,0.999417,1.642566,25.205168,15.206569,2500.0,TIQ_fluid


## Interpreting the first comparison

The key quantities to watch are:

- served rate
- abandonment rate
- $L_q$, the time-average queue length
- $L$, the time-average number in system

In this setting, $L_q$ is the main congestion metric of interest.

A useful fluid-TIQ policy should preserve overall throughput while reducing queue mass relative to FCFS or LCFS.

## Step 4: Local search around the fluid solution

The fluid thresholds are derived from an asymptotic approximation.

The stochastic finite-server system may perform slightly better with nearby thresholds.

So we perform a small grid search around the fluid pair and use simulation to identify the best local thresholds.

The fluid solution provides a theoretically motivated starting point, but the simulator operates in a finite-$N$ regime.

A local search therefore helps answer a practical question:

Does the fluid solution land near the best implementable TIQ policy, or is a noticeable adjustment needed?

In [ ]:
wl_grid = [max(0.0, sol.w_l + d) for d in (-0.2, -0.1, 0.0, 0.1, 0.2)]
wh_grid = [max(wl, sol.w_h + d) for d in (-0.5, -0.25, 0.0, 0.25, 0.5) for wl in wl_grid]

best = None

for wl in wl_grid:
    for wh in [max(wl, sol.w_h + d) for d in (-0.5, -0.25, 0.0, 0.25, 0.5)]:
        cfg = SimConfig(
            n_servers=N,
            interarrival=interarrival,
            service=service,
            patience=patience,
            policy=TIQ(w_l=wl, w_h=wh),
            seed=seed,
            warmup_time=warmup_time,
            run_time=run_time,
            collect_event_log=False,
        )
        res = run_sim(cfg)

        # Use congestion metric (time-average Lq) instead of served-only waits
        stats = time_average_L(res)
        score = stats["Lq"]

        if best is None or score < best["score"]:
            best = {"w_l": wl, "w_h": wh, "score": score, "res": res}

best

{'w_l': 0.44612936757323707,
 'w_h': 0.9516725001250105,
 'score': 15.170056800132363,
 'res': SimResult(config=SimConfig(n_servers=10, interarrival=Exponential(rate=20.0), service=Exponential(rate=1.0), patience=LogNormal(meanlog=0.0, sdlog=1.0), policy=TIQ(w_l=0.44612936757323707, w_h=0.9516725001250105, name='TIQ'), seed=123, warmup_time=500.0, run_time=2000.0, collect_event_log=False), customers=[CustomerRecord(customer_id=0, arrival_time=0.013303134112406231, service_time=1.2112923414316508, patience_time=1.5071051904248502, abandon_time=1.5204083245372564, service_start=0.013303134112406231, service_end=1.224595475544057, outcome='SERVED'), CustomerRecord(customer_id=1, arrival_time=0.06812985973763375, service_time=0.3589240959496531, patience_time=0.9640208488816525, abandon_time=1.0321507086192863, service_start=0.06812985973763375, service_end=0.4270539556872868, outcome='SERVED'), CustomerRecord(customer_id=2, arrival_time=0.09751731155916175, service_time=1.3156872966972675

## Step 5: Final comparison

Finally, we compare:

- FCFS
- LCFS
- the best locally tuned TIQ

This isolates the practical gain from threshold tuning and shows whether TIQ can improve queueing performance beyond the standard benchmark policies.

In [9]:
# Rerun and report best TIQ vs FCFS/LCFS using congestion metrics

from gi_gi_n_gi_multiclass.metrics.basic import summary_table
from gi_gi_n_gi_multiclass.metrics.steady_state import time_average_L

results = []

for pol_name, pol in {
    "FCFS": FCFS(),
    "LCFS": LCFS(),
    "TIQ_best_local": TIQ(w_l=best["w_l"], w_h=best["w_h"]),
}.items():
    cfg = SimConfig(
        n_servers=N,
        interarrival=interarrival,
        service=service,
        patience=patience,
        policy=pol,
        seed=seed,
        warmup_time=warmup_time,
        run_time=run_time,
        collect_event_log=False,
    )
    res = run_sim(cfg)
    tbl = summary_table(res)
    stats = time_average_L(res)
    tbl["L_timeavg"] = stats["L"]
    tbl["Lq_timeavg"] = stats["Lq"]
    tbl["policy_name"] = pol_name
    results.append(tbl)

pd.concat(results, ignore_index=True)[
    ["policy_name", "lambda_hat", "served_rate", "abandon_rate", "Lq_timeavg", "L_timeavg"]
].sort_values("policy_name")

,policy_name,lambda_hat,served_rate,abandon_rate,Lq_timeavg,L_timeavg
0,FCFS,20.0135,9.9440,10.0600,15.248472,25.247650
1,LCFS,20.0135,9.9905,10.0145,16.940421,26.940251
2,TIQ_best_local,20.0135,9.9945,10.0090,15.170057,25.169065


## Takeaway

This notebook connects fluid analysis to simulation.

It shows how to:

- solve for candidate TIQ thresholds
- implement the resulting policy
- refine the thresholds in simulation
- compare the final policy with FCFS and LCFS

This is the main bridge between the theoretical TIQ structure and the empirical queueing experiments used later in the project.